In [0]:
from pyspark.sql.functions import *
from pyspark.sql.types import *
from pyspark.sql.window import Window

# Data Reading

In [0]:
df = spark.read.format("parquet").load("abfss://bronze@databricksetlpractice.dfs.core.windows.net/orders/*.parquet")

In [0]:
display(df)

order_id,customer_id,product_id,order_date,quantity,total_amount,_rescued_data
O00001,C00710,P0159,2023-03-22,3,2022.87,null
O00002,C00954,P0036,2023-06-30,2,3560.74,null
O00003,C01578,P0427,2023-11-06,3,5903.52,null
O00004,C00962,P0332,2024-02-27,3,4107.99,null
O00005,C00156,P0038,2024-10-13,5,5784.95,null
O00006,C00521,P0174,2023-05-17,5,407.75,null
O00007,C00982,P0352,2024-01-18,4,4907.64,null
O00008,C00976,P0172,2023-01-10,4,7037.88,null
O00009,C01001,P0238,2023-04-20,3,4076.97,null
O00010,C00702,P0258,2023-07-07,4,5695.64,null


In [0]:
df.printSchema()

root
 |-- order_id: string (nullable = true)
 |-- customer_id: string (nullable = true)
 |-- product_id: string (nullable = true)
 |-- order_date: date (nullable = true)
 |-- quantity: integer (nullable = true)
 |-- total_amount: double (nullable = true)
 |-- _rescued_data: string (nullable = true)



In [0]:
df=df.withColumnRenamed("_rescued_data","rescued_data")

In [0]:
df = df.drop("rescued_data")
display(df)



order_id,customer_id,product_id,order_date,quantity,total_amount
O00001,C00710,P0159,2023-03-22,3,2022.87
O00002,C00954,P0036,2023-06-30,2,3560.74
O00003,C01578,P0427,2023-11-06,3,5903.52
O00004,C00962,P0332,2024-02-27,3,4107.99
O00005,C00156,P0038,2024-10-13,5,5784.95
O00006,C00521,P0174,2023-05-17,5,407.75
O00007,C00982,P0352,2024-01-18,4,4907.64
O00008,C00976,P0172,2023-01-10,4,7037.88
O00009,C01001,P0238,2023-04-20,3,4076.97
O00010,C00702,P0258,2023-07-07,4,5695.64


In [0]:
df=df.withColumn("order_date",to_timestamp(col("order_date")))

In [0]:
display(df)

order_id,customer_id,product_id,order_date,quantity,total_amount
O00001,C00710,P0159,2023-03-22T00:00:00.000Z,3,2022.87
O00002,C00954,P0036,2023-06-30T00:00:00.000Z,2,3560.74
O00003,C01578,P0427,2023-11-06T00:00:00.000Z,3,5903.52
O00004,C00962,P0332,2024-02-27T00:00:00.000Z,3,4107.99
O00005,C00156,P0038,2024-10-13T00:00:00.000Z,5,5784.95
O00006,C00521,P0174,2023-05-17T00:00:00.000Z,5,407.75
O00007,C00982,P0352,2024-01-18T00:00:00.000Z,4,4907.64
O00008,C00976,P0172,2023-01-10T00:00:00.000Z,4,7037.88
O00009,C01001,P0238,2023-04-20T00:00:00.000Z,3,4076.97
O00010,C00702,P0258,2023-07-07T00:00:00.000Z,4,5695.64


In [0]:
df=df.withColumn("year",year(col("order_date")))



In [0]:
display(df)

order_id,customer_id,product_id,order_date,quantity,total_amount,year
O00001,C00710,P0159,2023-03-22T00:00:00.000Z,3,2022.87,2023
O00002,C00954,P0036,2023-06-30T00:00:00.000Z,2,3560.74,2023
O00003,C01578,P0427,2023-11-06T00:00:00.000Z,3,5903.52,2023
O00004,C00962,P0332,2024-02-27T00:00:00.000Z,3,4107.99,2024
O00005,C00156,P0038,2024-10-13T00:00:00.000Z,5,5784.95,2024
O00006,C00521,P0174,2023-05-17T00:00:00.000Z,5,407.75,2023
O00007,C00982,P0352,2024-01-18T00:00:00.000Z,4,4907.64,2024
O00008,C00976,P0172,2023-01-10T00:00:00.000Z,4,7037.88,2023
O00009,C01001,P0238,2023-04-20T00:00:00.000Z,3,4076.97,2023
O00010,C00702,P0258,2023-07-07T00:00:00.000Z,4,5695.64,2023


In [0]:
df.filter(df.order_id.isNull()).display()

order_id,customer_id,product_id,order_date,quantity,total_amount,year


In [0]:
df.groupBy("_metadata.file_name").count().display()

file_name,count
part-00000-d7bb7579-02a1-4828-b110-09a72594d642.c000.snappy.parquet,9990
part-00000-tid-4684755778947285767-ed1e9e04-2177-493c-ae8b-cadfb096c5a3-194-1.c000.snappy.parquet,9990
part-00001-aa268037-a57a-4865-8f88-9c96102b62c7.c000.snappy.parquet,10


In [0]:
df1=df.withColumn("flag",dense_rank().over(Window.partitionBy("year").orderBy(desc("total_amount"))))

In [0]:
df1.display()

order_id,customer_id,product_id,order_date,quantity,total_amount,year,flag
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,1
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,1
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,1
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,1
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,1
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,1
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,1
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,1
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,1
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,1


In [0]:
df1=df.withColumn("flag_rank",rank().over(Window.partitionBy("year").orderBy(desc("total_amount"))))

In [0]:
df1.display()

order_id,customer_id,product_id,order_date,quantity,total_amount,year,flag_rank
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,1
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,1
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,1
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,1
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,1
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,1
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,1
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,1
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,1
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,1


In [0]:
df1=df.withColumn("flag",row_number().over(Window.partitionBy("year").orderBy(desc("total_amount"))))

In [0]:
df1.display()

order_id,customer_id,product_id,order_date,quantity,total_amount,year,flag
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,1
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,2
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,3
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,4
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,5
O00957,C01449,P0498,2023-10-05T00:00:00.000Z,5,9952.9,2023,6
O01765,C01515,P0498,2023-05-11T00:00:00.000Z,5,9952.9,2023,7
O03502,C00805,P0498,2023-09-24T00:00:00.000Z,5,9952.9,2023,8
O03660,C01001,P0498,2023-10-08T00:00:00.000Z,5,9952.9,2023,9
O06790,C01819,P0498,2023-02-27T00:00:00.000Z,5,9952.9,2023,10


# Data Writing

In [0]:
df.write.format("delta") \
    .mode("append") \
    .save("abfss://silver@databricksetlpractice.dfs.core.windows.net/orders")